In [18]:

import pandas as pd
import numpy as np
import plotly.express as px
import plotly.graph_objects as go
from plotly.subplots import make_subplots
from datetime import datetime

pd.set_option("display.max_columns", 50)
pd.set_option("display.width", 200)
pd.set_option("display.float_format", lambda x: f"{x:,.2f}")

# Shared colour palette so every chart reads consistently
PALETTE = px.colors.qualitative.Bold
PRIMARY = "#1f77b4"
ACCENT  = "#ff7f0e"

In [19]:
cleaned_customer_transaction = pd.read_csv("../customer_data/artifacts/cleaned_transaction_data.csv")

In [20]:
cleaned_customer_transaction.head(10)

,TransactionID,CustomerID,TransactionDate,TransactionTime,TransactionType,TransactionAmount,TransactionCurrency,AssetType,CustomerDOB,CustGender,CustLocation,CustAccountBalance,WalletActivity,TransactionStatus
0,TXN00000001,CUST00001,2024-12-13,10:03:23,P2P Transfer,79.36,GBP,Traditional,2007-04-30,Male,London,"4,716.01",0,Completed
1,TXN00000002,CUST00001,2024-12-13,17:15:53,Bill Payment,54.95,GBP,Traditional,2007-04-30,Male,London,"4,661.06",0,Completed
2,TXN00000003,CUST00001,2024-12-14,12:26:16,Wallet Transfer,410.02,GBP,Traditional,2007-04-30,Male,London,"5,071.08",1,Completed
3,TXN00000004,CUST00001,2024-12-14,13:10:09,Withdrawal,212.52,USD,Traditional,2007-04-30,Male,London,"4,905.31",0,Completed
4,TXN00000005,CUST00001,2024-12-14,20:13:04,Bill Payment,674.77,GBP,Traditional,2007-04-30,Male,London,"4,230.54",0,Completed
5,TXN00000006,CUST00001,2024-12-15,07:10:38,Crypto Buy,74.81,USDT,USDT,2007-04-30,Male,London,"4,172.19",1,Completed
6,TXN00000007,CUST00001,2024-12-15,11:41:13,Cross-Border Payment,441.29,EUR,Traditional,2007-04-30,Male,London,"3,797.09",0,Completed
7,TXN00000008,CUST00001,2024-12-15,19:27:06,Deposit,275.91,EUR,Traditional,2007-04-30,Male,London,"4,031.62",0,Completed
8,TXN00000009,CUST00001,2024-12-16,17:44:56,Deposit,169.85,USD,Traditional,2007-04-30,Male,London,"4,164.10",0,Completed
9,TXN00000010,CUST00001,2024-12-21,08:17:59,P2P Transfer,182.63,USD,Traditional,2007-04-30,Male,London,"4,021.65",0,Completed


In [21]:
cleaned_customer_transaction.info()

<class 'pandas.core.frame.DataFrame'>
RangeIndex: 580962 entries, 0 to 580961
Data columns (total 14 columns):
 #   Column               Non-Null Count   Dtype  
---  ------               --------------   -----  
 0   TransactionID        580962 non-null  object 
 1   CustomerID           580962 non-null  object 
 2   TransactionDate      580962 non-null  object 
 3   TransactionTime      580962 non-null  object 
 4   TransactionType      580962 non-null  object 
 5   TransactionAmount    580962 non-null  float64
 6   TransactionCurrency  580962 non-null  object 
 7   AssetType            580962 non-null  object 
 8   CustomerDOB          580962 non-null  object 
 9   CustGender           580962 non-null  object 
 10  CustLocation         580962 non-null  object 
 11  CustAccountBalance   580962 non-null  float64
 12  WalletActivity       580962 non-null  int64  
 13  TransactionStatus    580962 non-null  object 
dtypes: float64(2), int64(1), object(11)
memory usage: 62.1+ MB


In [22]:
cleaned_customer_transaction.isna().sum()

TransactionID          0
CustomerID             0
TransactionDate        0
TransactionTime        0
TransactionType        0
TransactionAmount      0
TransactionCurrency    0
AssetType              0
CustomerDOB            0
CustGender             0
CustLocation           0
CustAccountBalance     0
WalletActivity         0
TransactionStatus      0
dtype: int64

In [23]:
# Parse dates once, reuse everywhere
cleaned_customer_transaction["TransactionDate"] = pd.to_datetime(cleaned_customer_transaction["TransactionDate"])
cleaned_customer_transaction["CustomerDOB"]     = pd.to_datetime(cleaned_customer_transaction["CustomerDOB"])
cleaned_customer_transaction["TransactionTime"] = pd.to_datetime(cleaned_customer_transaction["TransactionTime"], format="%H:%M:%S").dt.time

print(f"Rows:      {len(cleaned_customer_transaction):,}")
print(f"Columns:   {cleaned_customer_transaction.shape[1]}")
print(f"Customers: {cleaned_customer_transaction['CustomerID'].nunique():,}")
print(f"Date range: {cleaned_customer_transaction['TransactionDate'].min().date()} → {cleaned_customer_transaction['TransactionDate'].max().date()}")
print(f"Total nulls: {cleaned_customer_transaction.isna().sum().sum()}")

Rows:      580,962
Columns:   14
Customers: 4,997
Date range: 2024-12-13 → 2026-09-12
Total nulls: 0


In [24]:
cleaned_customer_transaction["TransactionStatus"].value_counts()

TransactionStatus
Completed       544678
Pending          23325
Failed            5517
Under Review      4170
Rejected          3272
Name: count, dtype: int64

### Feature Engineering — Enabling Monetary, Temporal & Demographic Plots

This block adds a set of derived columns to `cleaned_customer_transaction` that unlock the visualisations and analyses used throughout the rest of the notebook. Each new column exists to serve a specific plot or metric downstream.

---

#### Monetary Analysis (`AmountGBP`, `RevenueGBP`)

Because transactions arrive in mixed currencies — fiat (GBP/EUR/USD), stablecoins, and crypto (BTC/ETH) — raw `TransactionAmount` values are **not comparable across rows**. A fixed FX lookup converts every row to a single **GBP-equivalent** figure so monetary charts are meaningful.

- **`AmountGBP`** — the GBP value of every transaction, regardless of original currency. Enables:
  - Transaction volume/value distributions
  - Spend per customer, per asset, per location
  - Time-series of transaction value
- **`RevenueGBP`** — a **revenue-recognised** version that counts only `Completed` transactions; failed, rejected, pending, and under-review rows contribute **0**. Enables:
  - True revenue trends (excluding failed/abandoned activity)
  - Revenue vs. gross volume comparisons
  - Success-rate impact on earnings

> **Note:** The FX rates are static approximations, so `AmountGBP` is intended for *relative* comparisons and charting — not for accounting-grade accuracy.

---

#### Temporal Analysis (`Year`, `Month`, `DayOfWeek`, `Hour`, plus `SNAPSHOT`)

Date and time are split into separate components so trends can be sliced along any axis.

- **`SNAPSHOT`** — the latest transaction date in the dataset, used as the "as of" reference point for recency (RFM) calculations.
- **`Year`** / **`Month`** — support monthly and yearly time-series:
  - Revenue over time, transaction counts over time
  - Month-over-month growth, seasonality
- **`DayOfWeek`** — enables day-of-week patterns:
  - Which days see peak activity or revenue?
  - Weekday vs. weekend behaviour
- **`Hour`** — enables intraday patterns:
  - Hourly transaction heatmaps
  - Peak-hour identification for staffing / fraud monitoring

---

#### Demographic Analysis (`Age`)

- **`Age`** — customer age at the snapshot date, computed from `CustomerDOB`. Enables:
  - Age distribution histograms
  - Spend / revenue by age band
  - Age vs. asset-type or transaction-type preference

---

### Why These Together

These engineered features cover the four pillars most analytics notebooks need:

| Pillar | Column(s) | Powers |
|---|---|---|
| **Money** | `AmountGBP`, `RevenueGBP` | Value distributions, revenue trends |
| **Time** | `Year`, `Month`, `DayOfWeek`, `Hour`, `SNAPSHOT` | Time-series, seasonality, recency |
| **Demographics** | `Age` | Customer segmentation |
| **Recency anchor** | `SNAPSHOT` | RFM scoring, cohort analysis |

The `print("Derived columns added.")` confirms the enrichment step completed successfully.

In [25]:
# GBP-equivalent amount (needed for monetary charts; crypto rows are in asset units)
FX_TO_GBP = {"GBP": 1.0, "EUR": 0.85, "USD": 0.78, "USDT": 0.78,
             "BTC": 42_000.0, "ETH": 2_300.0}

cleaned_customer_transaction["AmountGBP"] = cleaned_customer_transaction["TransactionAmount"] * cleaned_customer_transaction["TransactionCurrency"].map(FX_TO_GBP)
# Revenue-recognised amount: only Completed transactions count toward revenue.
# Failed / Rejected / Pending / Under Review rows carry 0 revenue.
cleaned_customer_transaction["RevenueGBP"] = np.where(
    cleaned_customer_transaction["TransactionStatus"] == "Completed",
    cleaned_customer_transaction["AmountGBP"],
    0.0,
)
# Recency anchor: latest transaction in the dataset
SNAPSHOT = cleaned_customer_transaction["TransactionDate"].max()

# Time components
cleaned_customer_transaction["Year"]    = cleaned_customer_transaction["TransactionDate"].dt.year
cleaned_customer_transaction["Month"]    = cleaned_customer_transaction["TransactionDate"].dt.to_period("M").astype(str)
cleaned_customer_transaction["DayOfWeek"] = cleaned_customer_transaction["TransactionDate"].dt.day_name()
cleaned_customer_transaction["Hour"]     = cleaned_customer_transaction["TransactionTime"].apply(lambda t: t.hour)

# Customer age at time of snapshot
cleaned_customer_transaction["Age"] = ((SNAPSHOT - cleaned_customer_transaction["CustomerDOB"]).dt.days / 365.25).round(1)

print("Derived columns added.")

Derived columns added.


### Plot — Distribution of Transaction Amount (GBP equivalent)

A histogram showing how transaction values are distributed after normalising every row to its GBP equivalent. This is the first look at the **shape of monetary activity** across the dataset.

---

#### What it shows
- **X-axis** — `AmountGBP`, binned into 80 buckets, spanning the full range of transaction values (from tiny wallet moves to large crypto trades).
- **Y-axis** — Number of transactions, plotted on a **log scale**. The log axis is essential here because transaction amounts are typically **heavily right-skewed** — a small number of very large transactions would otherwise flatten the bulk of activity into an invisible sliver near zero.
- **Bar gap** — Set small (0.02) so bins read as a near-continuous distribution curve.

---

#### What to look for
- **Skew & shape** — Is the distribution roughly log-normal (typical for financial data), or are there distinct modes (e.g., one for fiat micro-payments, another for crypto trades)?
- **Long tail** — The right tail reveals high-value outliers. Worth investigating whether they're genuine whale activity or FX-conversion artefacts.
- **Bulk concentration** — Where does the mass of transactions sit? This informs reasonable thresholds for "small," "medium," and "large" transactions later.
- **Zero / near-zero spike** — A pile-up at the low end can indicate failed or near-zero-value transactions surviving into the dataset.



In [26]:
fig = px.histogram(
    cleaned_customer_transaction, x="AmountGBP", nbins=80,
    title="Distribution of Transaction Amount (GBP equivalent)",
    labels={"AmountGBP": "Amount (GBP)"},
    color_discrete_sequence=[PRIMARY],
)
fig.update_layout(bargap=0.02, height=450)
fig.update_yaxes(title="Number of transactions", type="log")
fig.show()

In [27]:
cleaned_customer_transaction["log_Amount"] = np.log10(cleaned_customer_transaction["AmountGBP"].clip(lower=0.01))

fig = px.histogram(
    cleaned_customer_transaction, x="log_Amount", nbins=80,
    title="Distribution of log10(Transaction Amount) — GBP",
    labels={"log_Amount": "log10(Amount in GBP)"},
    color_discrete_sequence=[PRIMARY],
)
fig.update_layout(bargap=0.02, height=450)
fig.show()

### Plot — Customer Age Distribution

A histogram of unique customers by age (one row per customer, so high-activity users don't skew the shape).

**Used to check:**
- **Data quality** — flags impossible ages (negative, or 100+) from bad DOB values.
- **Customer base profile** — shows which age band dominates and whether the base is concentrated or spread.
- **Segment baseline** — a reference for later age-based comparisons (e.g., spend or asset type by age).

In [28]:
unique_cust = cleaned_customer_transaction.drop_duplicates("CustomerID")[["CustomerID", "Age", "CustGender", "CustLocation"]]
unique_cust.shape
fig = px.histogram(
    unique_cust, x="Age", nbins=40,
    title="Customer Age Distribution",
    color_discrete_sequence=[PRIMARY],
)
fig.update_layout(bargap=0.03, height=420)
fig.update_yaxes(title="Number of customers")
fig.show()

In [29]:
gender_counts = unique_cust["CustGender"].value_counts().reset_index()
gender_counts.columns = ["Gender", "Count"]

fig = px.pie(
    gender_counts, names="Gender", values="Count",
    title="Customer Gender Split",
    color_discrete_sequence=PALETTE,
    hole=0.5,
)
fig.update_traces(textinfo="label+percent")
fig.show()

### Plot — Total Transaction Value by Type (GBP)

A bar chart ranking each `TransactionType` by total `RevenueGBP`, with the transaction count shown on hover.

**Used to check:**
- **Which transaction types drive the most value** — identifies the dominant revenue sources.
- **Value vs. frequency mismatch** — a type with high count but low value (or vice versa) reveals whether revenue comes from many small transactions or few large ones.
- **Distribution across types** — shows whether value is concentrated in one or two types or spread evenly.

In [30]:
import plotly.express as px

agg = (cleaned_customer_transaction
       .groupby("TransactionType", as_index=False)
       .agg(TotalAmount=("RevenueGBP", "sum"),
            Count=("RevenueGBP", "size"))
       .sort_values("TotalAmount", ascending=False))

fig = px.bar(
    agg, x="TransactionType", y="TotalAmount",
    title="Total Transaction Value by Type (GBP equivalent)",
    text="TotalAmount",
    color="TransactionType",
    color_discrete_sequence=PALETTE,
    hover_data={"Count": ":,"},
)
fig.update_traces(texttemplate="£%{text:,.0f}", textposition="outside")
fig.update_layout(height=500, showlegend=False)
fig.update_xaxes(tickangle=-30)
fig.update_yaxes(title="Total value (GBP)")
fig.show()

### Plot — Customer & Channel Composition (4-panel dashboard)

A 2×2 subplot dashboard summarising **who the customers are** and **how they transact**.

**Panels:**
1. **Age distribution** — histogram of unique customers by age.
2. **Gender split** — donut chart of male/female/other.
3. **Top 15 locations** — horizontal bar of the most common customer locations.
4. **Wallet / Crypto vs Traditional** — donut showing the share of wallet/crypto transactions versus traditional ones.

**Used to check:**
- **Channel mix** — how much activity flows through wallet/crypto versus traditional rails.
- **Segment concentration** — whether the base is diverse or dominated by one demographic or region.

In [31]:
unique_cust = cleaned_customer_transaction.drop_duplicates("CustomerID")[
    ["CustomerID", "Age", "CustGender", "CustLocation"]]

fig = make_subplots(
    rows=2, cols=2,
    subplot_titles=(
        "Customer age distribution",
        "Gender split",
        "Top 15 customer locations",
        "Wallet / crypto share of transactions",
    ),
    specs=[[{"type": "xy"}, {"type": "domain"}],
           [{"type": "xy"}, {"type": "domain"}]],
    vertical_spacing=0.20, horizontal_spacing=0.15,
)

# 1. Age histogram — go.Histogram, NOT px.histogram
fig.add_trace(
    go.Histogram(x=unique_cust["Age"], nbinsx=40, marker_color=PRIMARY),
    row=1, col=1,
)

# 2. Gender pie
gender = unique_cust["CustGender"].value_counts()
fig.add_trace(
    go.Pie(labels=gender.index, values=gender.values, hole=0.5,
           marker=dict(colors=PALETTE), textinfo="label+percent"),
    row=1, col=2,
)

# 3. Top 15 locations
loc = unique_cust["CustLocation"].value_counts().head(15).reset_index()
loc.columns = ["Location", "Customers"]
fig.add_trace(
    go.Bar(x=loc["Customers"], y=loc["Location"], orientation="h",
           marker_color=PRIMARY),
    row=2, col=1,
)

# 4. Wallet activity pie
wallet = cleaned_customer_transaction["WalletActivity"].value_counts()
labels = wallet.index.map({0: "Traditional", 1: "Wallet / Crypto"})
fig.add_trace(
    go.Pie(labels=labels, values=wallet.values, hole=0.5,
           marker=dict(colors=[PALETTE[0], PALETTE[1]]),
           textinfo="label+percent"),
    row=2, col=2,
)

fig.update_yaxes(autorange="reversed", row=2, col=1)
fig.update_xaxes(title="Age", row=1, col=1)
fig.update_layout(height=750, title_text="Customer and Channel Composition",
                  showlegend=False)
fig.show()

### Plot — Ledger Health Overview (4-panel dashboard)

A 2×2 dashboard summarising the **composition of the transaction ledger** across four key categorical fields.

**Panels:**
1. **Transaction status** — count of Completed / Failed / Pending / etc.
2. **Transaction type** — frequency of each type (Deposit, Withdrawal, Crypto Buy, …).
3. **Currency** — how many transactions run in each currency.
4. **Asset type** — split across Traditional / Stablecoin / BTC / ETH.

**Used to check:**
- **Ledger health** — the success/failure ratio (are most transactions completing?).
- **Activity mix** — which transaction types dominate and whether the ledger is diversified or concentrated.
- **Currency & asset exposure** — how much activity is fiat versus crypto, and which currencies carry the load.
- **Data quality** — unexpected spikes (e.g., a large `Unknown` bucket) flag imputation or source issues.

In [32]:
fig = make_subplots(
    rows=2, cols=2,
    subplot_titles=(
        "Transaction status distribution",
        "Transaction type frequency",
        "Currency distribution",
        "Asset type distribution",
    ),
    vertical_spacing=0.18, horizontal_spacing=0.12,
)

status = cleaned_customer_transaction["TransactionStatus"].value_counts()
fig.add_trace(
    go.Bar(x=status.index, y=status.values, marker_color=PALETTE[:len(status)],
           text=status.values, texttemplate="%{text:,}", textposition="outside"),
    row=1, col=1,
)

ttype = cleaned_customer_transaction["TransactionType"].value_counts()
fig.add_trace(
    go.Bar(x=ttype.index, y=ttype.values, marker_color=PRIMARY,
           text=ttype.values, texttemplate="%{text:,}", textposition="outside"),
    row=1, col=2,
)

cur = cleaned_customer_transaction["TransactionCurrency"].value_counts()
fig.add_trace(
    go.Bar(x=cur.index, y=cur.values, marker_color=ACCENT,
           text=cur.values, texttemplate="%{text:,}", textposition="outside"),
    row=2, col=1,
)

asset = cleaned_customer_transaction["AssetType"].value_counts()
fig.add_trace(
    go.Bar(x=asset.index, y=asset.values, marker_color=PALETTE[2],
           text=asset.values, texttemplate="%{text:,}", textposition="outside"),
    row=2, col=2,
)

fig.update_xaxes(tickangle=-30, row=1, col=2)
fig.update_xaxes(tickangle=-30, row=2, col=2)
fig.update_layout(height=750, title_text="Ledger Health Overview",
                  showlegend=False, bargap=0.25)
fig.show()

### Plot — Temporal Behaviour (4-panel dashboard)

A 2×2 dashboard showing **when transactions happen** across four time scales.

**Panels:**
1. **Monthly volume** — transaction count per month (line/area chart) for trend and seasonality.
2. **Day-of-week pattern** — bar chart of activity by weekday (Mon → Sun).
3. **Hour-of-day pattern** — line chart of activity by hour (0–23).
4. **Hour × day heatmap** — density of transactions for every hour/day combination.

**Used to check:**
- **Trends over time** — whether volume is growing, flat, or seasonal across months.
- **Weekly rhythm** — which days see peak and trough activity.
- **Intraday rhythm** — peak hours for transactions (e.g., market open, evening).
- **Density hotspots** — the heatmap reveals exact high-traffic windows (e.g., weekday mornings) that single-axis plots can miss.

In [33]:
monthly = cleaned_customer_transaction.groupby("Month").size().reset_index(name="Count")
dow_order = ["Monday", "Tuesday", "Wednesday", "Thursday", "Friday", "Saturday", "Sunday"]
dow = (cleaned_customer_transaction.groupby("DayOfWeek").size()
       .reindex(dow_order).reset_index(name="Count"))
hourly = cleaned_customer_transaction.groupby("Hour").size().reset_index(name="Count")
heat = pd.crosstab(cleaned_customer_transaction["Hour"],
                   cleaned_customer_transaction["DayOfWeek"]).reindex(columns=dow_order)

fig = make_subplots(
    rows=2, cols=2,
    subplot_titles=(
        "Monthly transaction volume",
        "Day-of-week pattern",
        "Hour-of-day pattern",
        "Transaction density — hour × day",
    ),
    vertical_spacing=0.18, horizontal_spacing=0.12,
)

fig.add_trace(
    go.Scatter(x=monthly["Month"], y=monthly["Count"], mode="lines+markers",
               line=dict(color=PRIMARY, width=3), fill="tozeroy",
               fillcolor="rgba(31,119,180,0.15)"),
    row=1, col=1,
)

fig.add_trace(
    go.Bar(x=dow["DayOfWeek"], y=dow["Count"], marker_color=PRIMARY),
    row=1, col=2,
)

fig.add_trace(
    go.Scatter(x=hourly["Hour"], y=hourly["Count"], mode="lines+markers",
               line=dict(color=ACCENT, width=3)),
    row=2, col=1,
)

fig.add_trace(
    go.Heatmap(z=heat.values, x=heat.columns, y=heat.index,
               colorscale="Viridis", showscale=False),
    row=2, col=2,
)

fig.update_xaxes(tickangle=-45, row=1, col=1)
fig.update_xaxes(tickangle=-30, row=1, col=2)
fig.update_xaxes(dtick=2, title="Hour", row=2, col=1)
fig.update_yaxes(title="Hour", row=2, col=2)
fig.update_layout(height=750, title_text="Temporal Behaviour", showlegend=False)
fig.show()

### Plot — Transaction Status by Transaction Type

A grouped bar chart showing how transaction statuses (Completed, Failed, Pending, etc.) break down **within each transaction type**.

**Used to check:**
- **Success rate per type** — does a specific transaction type fail more often than others?
- **Status mix** — which statuses dominate each type (e.g., crypto buys mostly completed vs. cross-border payments mostly pending).
- **Failure hotspots** — surfaces transaction types that need operational attention.
- **Fair comparison across types** — since types have very different volumes, the normalised percentage version allows apples-to-apples comparison of failure/success rates.

In [34]:
import pandas as pd
import plotly.graph_objects as go
import plotly.express as px

# Cross-tab: rows = TransactionType, columns = TransactionStatus
status_by_type = pd.crosstab(
    cleaned_customer_transaction["TransactionType"],
    cleaned_customer_transaction["TransactionStatus"],
)

# Optional: normalise to percentages so success/failure mix is comparable across
# types with very different volumes. Comment out if you want raw counts.
status_by_type_pct = status_by_type.div(status_by_type.sum(axis=1), axis=0) * 100

# Plotly grouped bar — one trace per status, one x-tick per transaction type
fig = go.Figure()

for i, status in enumerate(status_by_type.columns):
    fig.add_trace(go.Bar(
        name=status,
        x=status_by_type.index,
        y=status_by_type[status],
        marker_color=px.colors.qualitative.Bold[i % 8],
        hovertemplate=(
            "<b>%{x}</b><br>"
            f"Status: {status}<br>"
            "Count: %{y:,}<extra></extra>"
        ),
    ))

fig.update_layout(
    barmode="group",
    title="Transaction Status by Transaction Type",
    xaxis_title="Transaction Type",
    yaxis_title="Number of Transactions",
    height=550,
    legend_title="Status",
)
fig.update_xaxes(tickangle=-30)
fig.show()

### Plot — Transaction Status Share by Transaction Type (%)

A grouped bar chart showing the **percentage breakdown of statuses within each transaction type**. Unlike the raw-count version, every transaction type sums to 100%, so the status *mix* is directly comparable across types regardless of volume.

**Used to check:**
- **Success rate per type** — what share of each type actually completes.
- **Failure/ pending hotspots** — which transaction types carry disproportionate failed, rejected, or under-review activity.
- **Fair comparison** — small-volume types aren't visually drowned out by high-volume ones.
- **Operational priorities** — highlights where to focus fixes or investigations.

In [35]:
fig = go.Figure()

for i, status in enumerate(status_by_type_pct.columns):
    fig.add_trace(go.Bar(
        name=status,
        x=status_by_type_pct.index,
        y=status_by_type_pct[status],
        marker_color=px.colors.qualitative.Bold[i % 8],
        hovertemplate=(
            "<b>%{x}</b><br>"
            f"Status: {status}<br>"
            "Share: %{y:.2f}%<extra></extra>"
        ),
    ))

fig.update_layout(
    barmode="group",
    title="Transaction Status Share by Transaction Type (%)",
    xaxis_title="Transaction Type",
    yaxis_title="% of transactions of that type",
    height=550,
    legend_title="Status",
)
fig.update_xaxes(tickangle=-30)
fig.show()

### Plot — Transaction Count by Currency and Asset Type

A grouped bar chart showing how transactions split across **currency × asset type** combinations. Each currency is broken down by the asset classes it settles.

**Used to check:**
- **Currency → asset mapping consistency** — confirm the expected 1:1 relationships hold (e.g., GBP → Traditional, BTC → BTC).
- **Unexpected pairings** — cross-combinations (e.g., GBP → BTC) reveal data-quality issues or unusual transaction flows.
- **Volume distribution** — which currency/asset pairings carry the bulk of activity.
- **Validation of imputation** — verifies the earlier currency and asset fills produced sensible combinations.

In [36]:
currency_asset = pd.crosstab(
    cleaned_customer_transaction["TransactionCurrency"],
    cleaned_customer_transaction["AssetType"],
)

fig = go.Figure()

for i, asset in enumerate(currency_asset.columns):
    fig.add_trace(go.Bar(
        name=asset,
        x=currency_asset.index,
        y=currency_asset[asset],
        marker_color=px.colors.qualitative.Bold[i % 8],
        hovertemplate=(
            "<b>%{x}</b><br>"
            f"Asset: {asset}<br>"
            "Count: %{y:,}<extra></extra>"
        ),
    ))

fig.update_layout(
    barmode="group",
    title="Transaction Count by Currency and Asset Type",
    xaxis_title="Transaction Currency",
    yaxis_title="Number of Transactions",
    height=550,
    legend_title="Asset Type",
)
fig.show()

### Plot — Total Transaction Value by Currency (GBP equivalent)

A bar chart ranking each `TransactionCurrency` by its total `AmountGBP`, with count, mean, and median shown on hover.

**Used to check:**
- **Which currencies carry the most value** — identifies the dominant currencies by total volume.
- **Value vs. frequency** — a currency with high count but low total (or vice versa) reveals whether it's used for many small or few large transactions.
- **Mean vs. median gap** — a large gap flags skewed distributions or outliers within a currency.
- **Currency concentration** — whether value is spread across many currencies or concentrated in one or two.

In [37]:
import pandas as pd
import plotly.graph_objects as go
import plotly.express as px

cur_agg = (cleaned_customer_transaction
           .groupby("TransactionCurrency", as_index=False)
           .agg(TotalGBP=("AmountGBP", "sum"),
                Count=("TransactionAmount", "size"),
                MeanGBP=("AmountGBP", "mean"),
                MedianGBP=("AmountGBP", "median"))
           .sort_values("TotalGBP", ascending=False))

fig = go.Figure()

for i, row in cur_agg.iterrows():
    fig.add_trace(go.Bar(
        name=row["TransactionCurrency"],
        x=[row["TransactionCurrency"]],
        y=[row["TotalGBP"]],
        marker_color=px.colors.qualitative.Bold[i % 8],
        text=[f"£{row['TotalGBP']:,.0f}"],
        textposition="outside",
        customdata=[[row["Count"], row["MeanGBP"], row["MedianGBP"]]],
        hovertemplate=(
            f"<b>{row['TransactionCurrency']}</b><br>"
            "Total: £%{y:,.0f}<br>"
            "Count: %{customdata[0]:,}<br>"
            "Mean: £%{customdata[1]:,.2f}<br>"
            "Median: £%{customdata[2]:,.2f}<extra></extra>"
        ),
        showlegend=False,
    ))

fig.update_layout(
    title="Total Transaction Value by Currency (GBP equivalent)",
    xaxis_title="Transaction Currency",
    yaxis_title="Total value (GBP)",
    height=520,
    bargap=0.4,
)
fig.show()

### Plot — Total Transaction Value by Currency (GBP equivalent)

A bar chart ranking each `TransactionCurrency` by its total `AmountGBP`, with count, mean, and median shown on hover.

**Used to check:**
- **Which currencies carry the most value** — identifies the dominant currencies by total volume.
- **Value vs. frequency** — a currency with high count but low total (or vice versa) reveals whether it's used for many small or few large transactions.
- **Mean vs. median gap** — a large gap flags skewed distributions or outliers within a currency.
- **Currency concentration** — whether value is spread across many currencies or concentrated in one or two.

In [38]:
import pandas as pd
import plotly.graph_objects as go
import plotly.express as px

cur_profile = (cleaned_customer_transaction
               .groupby("TransactionCurrency", as_index=False)
               .agg(Count=("TransactionID", "count"),
                    AttemptedGBP=("AmountGBP", "sum"),       # gross attempts
                    RevenueGBP=("RevenueGBP", "sum"),        # Completed only
                    CompletedCount=("TransactionStatus",
                                    lambda s: (s == "Completed").sum()),
                    CompletedPct=("TransactionStatus",
                                  lambda s: 100 * (s == "Completed").mean()),
                    UnderReviewPct=("TransactionStatus",
                                    lambda s: 100 * (s == "Under Review").mean()),
                    FailedPct=("TransactionStatus",
                               lambda s: 100 * (s == "Failed").mean()))
               .sort_values("RevenueGBP", ascending=False))

cur_profile["MeanRevenueGBP"] = (
    cur_profile["RevenueGBP"] / cur_profile["CompletedCount"]).round(2)

print(cur_profile.round(2).to_string(index=False))

TransactionCurrency  Count     AttemptedGBP       RevenueGBP  CompletedCount  CompletedPct  UnderReviewPct  FailedPct  MeanRevenueGBP
                GBP 295266 1,131,294,228.07 1,060,541,182.18          288237         97.62            0.69       0.97        3,679.41
               USDT  83999   533,482,412.37   431,681,801.11           70754         84.23            0.83       0.82        6,101.16
                USD  68322   365,830,275.81   337,381,552.43           66623         97.51            0.66       1.16        5,064.04
                EUR  58662   261,422,663.08   243,994,795.37           57261         97.61            0.65       1.05        4,261.10
                BTC  37437   217,628,742.29   173,569,562.80           31004         82.82            0.82       0.81        5,598.30
                ETH  37276   215,207,870.12   169,376,710.23           30799         82.62            0.78       0.71        5,499.42


### Plot — Currency Profile: Volume, Revenue & Mean Settled Value

A grouped bar chart comparing three metrics per currency on a **log scale**, so metrics with very different magnitudes (counts in the thousands vs. mean values in the tens) can be read side by side.

**Metrics shown:**
- **Transaction count** — how many transactions per currency.
- **Revenue (GBP, Completed)** — recognised revenue from completed transactions only.
- **Mean per settled transaction (GBP)** — average value of completed transactions.

**Used to check:**
- **Volume vs. value mismatch** — a currency high in count but low in revenue (or vice versa) reveals whether it's used for many small or few large transactions.
- **Revenue efficiency** — which currencies convert activity into actual recognised revenue.
- **High-value vs. high-frequency currencies** — separates workhorse currencies from niche high-ticket ones.
- **Log-scale comparison** — makes wildly different metrics readable without one dominating the chart.

In [39]:
fig = go.Figure()

metrics = [
    ("Count",          "Transaction count",         px.colors.qualitative.Bold[0]),
    ("RevenueGBP",     "Revenue (GBP, Completed)",  px.colors.qualitative.Bold[1]),
    ("MeanRevenueGBP", "Mean per settled txn (GBP)",px.colors.qualitative.Bold[2]),
]

for col, label, colour in metrics:
    fig.add_trace(go.Bar(
        name=label,
        x=cur_profile["TransactionCurrency"],
        y=cur_profile[col],
        marker_color=colour,
        hovertemplate=(
            "<b>%{x}</b><br>"
            f"{label}: %{{y:,.2f}}<extra></extra>"
        ),
    ))

fig.update_layout(
    barmode="group",
    title="Currency Profile — Volume, Recognised Revenue, Mean Settled Value",
    xaxis_title="Transaction Currency",
    yaxis_title="Value (log scale)",
    height=550,
    legend_title="Metric",
)
fig.update_yaxes(type="log")
fig.show()

### Plot — Transaction Status Share by Currency (%)

A grouped bar chart showing the **percentage breakdown of statuses within each currency**. Every currency sums to 100%, so the status mix is comparable across currencies regardless of volume.

**Used to check:**
- **Success rate per currency** — what share of each currency's transactions actually complete.
- **Failure / pending hotspots** — which currencies carry disproportionate failed, rejected, or under-review activity.
- **Currency-specific issues** — flags currencies where operational problems (FX, settlement, compliance) may be concentrated.
- **Fair comparison** — small-volume currencies aren't visually drowned out by high-volume ones.

In [40]:
status_by_cur = pd.crosstab(
    cleaned_customer_transaction["TransactionCurrency"],
    cleaned_customer_transaction["TransactionStatus"],
    normalize="index"
) * 100

fig = go.Figure()
for i, status in enumerate(status_by_cur.columns):
    fig.add_trace(go.Bar(
        name=status,
        x=status_by_cur.index,
        y=status_by_cur[status],
        marker_color=px.colors.qualitative.Bold[i % 8],
        hovertemplate=(
            "<b>%{x}</b><br>"
            f"Status: {status}<br>"
            "Share: %{y:.2f}%<extra></extra>"
        ),
    ))

fig.update_layout(
    barmode="group",
    title="Transaction Status Share by Currency (%)",
    xaxis_title="Transaction Currency",
    yaxis_title="% of transactions of that currency",
    height=520,
    legend_title="Status",
)
fig.show()

In [41]:
fig = go.Figure()

fig.add_trace(go.Bar(
    name="Attempted value (all statuses)",
    x=cur_profile["TransactionCurrency"],
    y=cur_profile["AttemptedGBP"],
    marker_color=px.colors.qualitative.Bold[8 % 8] if len(px.colors.qualitative.Bold) > 8 else px.colors.qualitative.Bold[0],
    opacity=0.4,
    hovertemplate="<b>%{x}</b><br>Attempted: £%{y:,.0f}<extra></extra>",
))

fig.add_trace(go.Bar(
    name="Recognised revenue (Completed only)",
    x=cur_profile["TransactionCurrency"],
    y=cur_profile["RevenueGBP"],
    marker_color=px.colors.qualitative.Bold[1],
    hovertemplate="<b>%{x}</b><br>Revenue: £%{y:,.0f}<extra></extra>",
))

fig.update_layout(
    barmode="group",
    title="Currency — Attempted Value vs Recognised Revenue (GBP)",
    xaxis_title="Transaction Currency",
    yaxis_title="GBP value",
    height=540,
    legend_title="Basis",
)
fig.show()

### Plot — Transaction Type: Count vs Total Value

A grouped bar chart comparing **how often** each transaction type occurs against **how much value** it carries. The log Y-axis lets high-frequency types (thousands of counts) and high-value types (millions in GBP) sit on the same chart without one flattening the other.

**Used to check:**
- **Frequency vs. value mismatch** — which types are high-volume but low-value (e.g., small wallet moves) versus low-volume but high-value (e.g., crypto trades).
- **Revenue contribution** — where the bulk of monetary value actually comes from, which may differ sharply from where the transaction count sits.
- **Portfolio balance** — whether value and volume are concentrated in a few types or spread across many.
- **Priority setting** — identifies which types matter most for volume-driven work versus value-driven work.

In [42]:
import pandas as pd
import plotly.graph_objects as go
import plotly.express as px

type_profile = (cleaned_customer_transaction
                .groupby("TransactionType", as_index=False)
                .agg(Count=("TransactionID", "count"),
                     TotalGBP=("AmountGBP", "sum"),
                     RevenueGBP=("RevenueGBP", "sum"),
                     MeanGBP=("AmountGBP", "mean"),
                     MedianGBP=("AmountGBP", "median"))
                .sort_values("TotalGBP", ascending=False))

type_profile["CountShare%"] = (100 * type_profile["Count"] / type_profile["Count"].sum()).round(2)
type_profile["ValueShare%"] = (100 * type_profile["TotalGBP"] / type_profile["TotalGBP"].sum()).round(2)

fig = go.Figure()

fig.add_trace(go.Bar(
    name="Transaction count",
    x=type_profile["TransactionType"],
    y=type_profile["Count"],
    marker_color=px.colors.qualitative.Bold[0],
    text=type_profile["Count"].apply(lambda v: f"{v:,}"),
    textposition="outside",
    hovertemplate="<b>%{x}</b><br>Count: %{y:,}<extra></extra>",
))

fig.add_trace(go.Bar(
    name="Total value (GBP)",
    x=type_profile["TransactionType"],
    y=type_profile["TotalGBP"],
    marker_color=px.colors.qualitative.Bold[1],
    text=type_profile["TotalGBP"].apply(lambda v: f"£{v/1e6:,.1f}M"),
    textposition="outside",
    hovertemplate="<b>%{x}</b><br>Total value: £%{y:,.0f}<extra></extra>",
))

fig.update_layout(
    barmode="group",
    bargap=0.25,
    bargroupgap=0.08,
    title="Transaction Type — Count vs Total Value",
    xaxis=dict(title="Transaction Type", tickangle=-30),
    yaxis=dict(title="Value (log scale)", type="log"),
    height=560,
    legend=dict(title="Metric", orientation="h", yanchor="bottom",
                y=1.02, xanchor="right", x=1),
)
fig.show()

In [43]:
import pandas as pd
import numpy as np
import plotly.graph_objects as go
import plotly.express as px

SNAPSHOT = cleaned_customer_transaction["TransactionDate"].max()

cust_profile = (cleaned_customer_transaction
                .groupby("CustomerID", as_index=False)
                .agg(Transactions=("TransactionID", "count"),
                     RevenueGBP=("RevenueGBP", "sum"),
                     AttemptedGBP=("AmountGBP", "sum"),
                     LastTxn=("TransactionDate", "max"),
                     FirstTxn=("TransactionDate", "min"),
                     UnderReview=("TransactionStatus",
                                  lambda s: (s == "Under Review").sum()),
                     Failed=("TransactionStatus",
                             lambda s: (s == "Failed").sum()),
                     Rejected=("TransactionStatus",
                               lambda s: (s == "Rejected").sum()),
                     Completed=("TransactionStatus",
                                lambda s: (s == "Completed").sum())))

cust_profile["Recency"] = (SNAPSHOT - cust_profile["LastTxn"]).dt.days
cust_profile["Tenure"] = (SNAPSHOT - cust_profile["FirstTxn"]).dt.days
cust_profile["CompletedPct"] = (100 * cust_profile["Completed"]
                                / cust_profile["Transactions"]).round(2)
cust_profile["ProblemPct"] = (
    100 * (cust_profile["Failed"] + cust_profile["Rejected"]
           + cust_profile["UnderReview"]) / cust_profile["Transactions"]).round(2)

top10 = cust_profile.sort_values("RevenueGBP", ascending=False).head(10)

print(top10[[
    "CustomerID", "Transactions", "RevenueGBP", "AttemptedGBP",
    "Recency", "CompletedPct", "ProblemPct",
]].round(2).to_string(index=False))

CustomerID  Transactions   RevenueGBP  AttemptedGBP  Recency  CompletedPct  ProblemPct
 CUST04653           477 5,718,822.52  7,214,298.53        2         91.40        1.89
 CUST01904           353 5,676,412.44  5,991,234.95        8         94.33        0.28
 CUST00776           427 5,661,780.20  6,483,276.93        1         91.10        1.87
 CUST02518           470 5,644,115.02  6,242,810.67        2         92.34        2.98
 CUST03051           369 5,638,139.80  7,085,147.62        6         91.06        3.52
 CUST01335           448 5,561,358.42  6,605,830.31        5         91.52        2.46
 CUST00923           402 5,521,550.99  6,568,564.71        1         90.55        2.49
 CUST02670           457 5,511,813.43  6,364,706.21        5         89.93        1.75
 CUST02435           452 5,488,624.69  6,372,743.86        1         91.81        1.55
 CUST02185           409 5,483,114.94  6,211,744.94        2         91.69        1.96


In [44]:
fig = go.Figure()

fig.add_trace(go.Bar(
    name="Revenue (Completed, GBP)",
    x=top10["CustomerID"],
    y=top10["RevenueGBP"],
    marker_color=px.colors.qualitative.Bold[0],
    text=top10["RevenueGBP"].apply(lambda v: f"£{v/1e6:,.2f}M"),
    textposition="outside",
    hovertemplate="<b>%{x}</b><br>Revenue: £%{y:,.0f}<extra></extra>",
    yaxis="y1",
))

fig.add_trace(go.Bar(
    name="Transaction count",
    x=top10["CustomerID"],
    y=top10["Transactions"],
    marker_color=px.colors.qualitative.Bold[2],
    text=top10["Transactions"],
    textposition="outside",
    hovertemplate="<b>%{x}</b><br>Transactions: %{y:,}<extra></extra>",
    yaxis="y1",
))

fig.update_layout(
    barmode="group",
    title="Top 10 Customers — Revenue vs Activity",
    xaxis=dict(title="Customer ID", tickangle=-30),
    yaxis=dict(title="Value (log scale)", type="log"),
    height=540,
    legend=dict(orientation="h", yanchor="bottom", y=1.02,
                xanchor="right", x=1),
)
fig.show()

In [45]:
top15_ids = cust_profile.sort_values("RevenueGBP", ascending=False).head(15)["CustomerID"]

monthly = (cleaned_customer_transaction[
              cleaned_customer_transaction["CustomerID"].isin(top15_ids)]
           .groupby(["CustomerID", "Month"])
           .size()
           .reset_index(name="Count"))

fig = px.line(
    monthly,
    x="Month",
    y="Count",
    color="CustomerID",
    title="Monthly Transaction Count — Top 15 Customers",
    markers=True,
    color_discrete_sequence=px.colors.qualitative.Bold,
)
fig.update_layout(
    height=560,
    xaxis=dict(title="Month", tickangle=-45),
    yaxis=dict(title="Transactions per month"),
    legend_title="CustomerID",
)
fig.show()

In [46]:
cust_profile["Segment"] = np.select(
    [cust_profile["Recency"] <= 30,
     cust_profile["Recency"] <= 90],
    ["Active (≤30d)", "Warm (31–90d)"],
    default="Declining (>90d)")

status_by_segment = (cust_profile
                     .groupby("Segment", as_index=False)
                     .agg(Customers=("CustomerID", "count"),
                          AvgTransactions=("Transactions", "mean"),
                          AvgRevenueGBP=("RevenueGBP", "mean"),
                          AvgProblemPct=("ProblemPct", "mean"),
                          AvgUnderReviewPct=("UnderReview",
                                             lambda s: 100 * s.mean()),
                          AvgFailedPct=("Failed",
                                        lambda s: 100 * s.mean()),
                          AvgRejectedPct=("Rejected",
                                          lambda s: 100 * s.mean()))
                     .round(2))

print(status_by_segment.to_string(index=False))

# Grouped bar for the visual
status_cols = ["AvgProblemPct", "AvgUnderReviewPct",
               "AvgFailedPct", "AvgRejectedPct"]
labels = {
    "AvgProblemPct": "Any problem (%)",
    "AvgUnderReviewPct": "Under Review (%)",
    "AvgFailedPct": "Failed (%)",
    "AvgRejectedPct": "Rejected (%)",
}

fig = go.Figure()
for i, col in enumerate(status_cols):
    fig.add_trace(go.Bar(
        name=labels[col],
        x=status_by_segment["Segment"],
        y=status_by_segment[col],
        marker_color=px.colors.qualitative.Bold[i],
        text=status_by_segment[col].apply(lambda v: f"{v:.2f}%"),
        textposition="outside",
        hovertemplate="<b>%{x}</b><br>" + labels[col] + ": %{y:.2f}%<extra></extra>",
    ))

fig.update_layout(
    barmode="group",
    title="Problem-Transaction Rates by Customer Recency Segment",
    xaxis_title="Customer segment (by recency)",
    yaxis_title="% of transactions with that status",
    height=520,
    legend=dict(orientation="h", yanchor="bottom", y=1.02,
                xanchor="right", x=1),
)
fig.show()

         Segment  Customers  AvgTransactions  AvgRevenueGBP  AvgProblemPct  AvgUnderReviewPct  AvgFailedPct  AvgRejectedPct
   Active (≤30d)       2221           175.29     623,465.34           2.76             135.43        163.67           98.78
Declining (>90d)       1483            72.89     198,646.83           1.85              30.41         72.35           42.21
   Warm (31–90d)       1293            64.61     570,174.66           3.51              54.99         62.57           34.96


In [47]:
import numpy as np
import plotly.graph_objects as go
import plotly.express as px
import pandas as pd

# Per-customer rate of each status (not a mean of means)
rates = (cust_profile
         .assign(
             UnderReviewRate=100 * cust_profile["UnderReview"] / cust_profile["Transactions"],
             FailedRate=100 * cust_profile["Failed"] / cust_profile["Transactions"],
             RejectedRate=100 * cust_profile["Rejected"] / cust_profile["Transactions"],
             CompletedRate=100 * cust_profile["Completed"] / cust_profile["Transactions"])
         .groupby("Segment", as_index=False)
         .agg(UnderReviewRate=("UnderReviewRate", "mean"),
              FailedRate=("FailedRate", "mean"),
              RejectedRate=("RejectedRate", "mean"),
              CompletedRate=("CompletedRate", "mean"))
         .round(2))

metrics = [
    ("CompletedRate",   "Completed",   px.colors.qualitative.Bold[2]),
    ("UnderReviewRate", "Under Review", px.colors.qualitative.Bold[3]),
    ("FailedRate",      "Failed",      px.colors.qualitative.Bold[4]),
    ("RejectedRate",    "Rejected",    px.colors.qualitative.Bold[5]),
]

fig = go.Figure()
for col, label, colour in metrics:
    fig.add_trace(go.Bar(
        name=label,
        x=rates["Segment"],
        y=rates[col],
        marker_color=colour,
        text=rates[col].apply(lambda v: f"{v:.2f}%"),
        textposition="outside",
        hovertemplate="<b>%{x}</b><br>" + label + ": %{y:.2f}%<extra></extra>",
    ))

fig.update_layout(
    barmode="group",
    title="Average Transaction-Status Rates by Customer Recency Segment",
    xaxis_title="Customer segment (based on days since last transaction)",
    yaxis_title="Average % of a customer's transactions",
    height=560,
    legend=dict(orientation="h", yanchor="bottom", y=1.02,
                xanchor="right", x=1),
)
fig.show()

print(rates.to_string(index=False))

         Segment  UnderReviewRate  FailedRate  RejectedRate  CompletedRate
   Active (≤30d)             1.27        0.92          0.57          93.13
Declining (>90d)             0.45        0.97          0.43          96.46
   Warm (31–90d)             2.02        0.94          0.55          94.22


In [48]:
cleaned_customer_transaction.head(10)

,TransactionID,CustomerID,TransactionDate,TransactionTime,TransactionType,TransactionAmount,TransactionCurrency,AssetType,CustomerDOB,CustGender,CustLocation,CustAccountBalance,WalletActivity,TransactionStatus,AmountGBP,RevenueGBP,Year,Month,DayOfWeek,Hour,Age,log_Amount
0,TXN00000001,CUST00001,2024-12-13,10:03:23,P2P Transfer,79.36,GBP,Traditional,2007-04-30,Male,London,"4,716.01",0,Completed,79.36,79.36,2024,2024-12,Friday,10,19.40,1.90
1,TXN00000002,CUST00001,2024-12-13,17:15:53,Bill Payment,54.95,GBP,Traditional,2007-04-30,Male,London,"4,661.06",0,Completed,54.95,54.95,2024,2024-12,Friday,17,19.40,1.74
2,TXN00000003,CUST00001,2024-12-14,12:26:16,Wallet Transfer,410.02,GBP,Traditional,2007-04-30,Male,London,"5,071.08",1,Completed,410.02,410.02,2024,2024-12,Saturday,12,19.40,2.61
3,TXN00000004,CUST00001,2024-12-14,13:10:09,Withdrawal,212.52,USD,Traditional,2007-04-30,Male,London,"4,905.31",0,Completed,165.77,165.77,2024,2024-12,Saturday,13,19.40,2.22
4,TXN00000005,CUST00001,2024-12-14,20:13:04,Bill Payment,674.77,GBP,Traditional,2007-04-30,Male,London,"4,230.54",0,Completed,674.77,674.77,2024,2024-12,Saturday,20,19.40,2.83
5,TXN00000006,CUST00001,2024-12-15,07:10:38,Crypto Buy,74.81,USDT,USDT,2007-04-30,Male,London,"4,172.19",1,Completed,58.35,58.35,2024,2024-12,Sunday,7,19.40,1.77
6,TXN00000007,CUST00001,2024-12-15,11:41:13,Cross-Border Payment,441.29,EUR,Traditional,2007-04-30,Male,London,"3,797.09",0,Completed,375.10,375.10,2024,2024-12,Sunday,11,19.40,2.57
7,TXN00000008,CUST00001,2024-12-15,19:27:06,Deposit,275.91,EUR,Traditional,2007-04-30,Male,London,"4,031.62",0,Completed,234.52,234.52,2024,2024-12,Sunday,19,19.40,2.37
8,TXN00000009,CUST00001,2024-12-16,17:44:56,Deposit,169.85,USD,Traditional,2007-04-30,Male,London,"4,164.10",0,Completed,132.48,132.48,2024,2024-12,Monday,17,19.40,2.12
9,TXN00000010,CUST00001,2024-12-21,08:17:59,P2P Transfer,182.63,USD,Traditional,2007-04-30,Male,London,"4,021.65",0,Completed,142.45,142.45,2024,2024-12,Saturday,8,19.40,2.15


In [49]:
cleaned_customer_transaction.isna().sum()

TransactionID          0
CustomerID             0
TransactionDate        0
TransactionTime        0
TransactionType        0
TransactionAmount      0
TransactionCurrency    0
AssetType              0
CustomerDOB            0
CustGender             0
CustLocation           0
CustAccountBalance     0
WalletActivity         0
TransactionStatus      0
AmountGBP              0
RevenueGBP             0
Year                   0
Month                  0
DayOfWeek              0
Hour                   0
Age                    0
log_Amount             0
dtype: int64

In [50]:
cleaned_customer_transaction.to_csv("../customer_data/artifacts/exploratory_data.csv", index=False)